## Assignment: Object detection

The goals of the assignment are:
* Put into practice acquired knowledge to detect and recognize objects of interest within a satellite image.

To address this problem, you must choose one of the following options:
*	Implement a sliding window strategy to process the whole image, and then train a classifier that determines whether each window includes or not an object of interest. In this way, you can use previous image classification model to infer the object category.
*	Build a single-stage object detection model (e.g., YOLO, SSD, RetinaNet, etc.).
*	Build a two-stage object detection model (e.g., Faster R-CNN, R-FCN, etc.).

Follow the link below to download the detection data set “xview_detection”: [https://drive.upm.es/s/P7nEf3Bygns7tbM](https://drive.upm.es/s/P7nEf3Bygns7tbM)

In [ ]:
import torch

print("PyTorch version:", torch.__version__)
print("CUDA available:", torch.cuda.is_available())

if torch.cuda.is_available():
    print("CUDA version:", torch.version.cuda)
    print("GPU count:", torch.cuda.device_count())
    print("GPU name:", torch.cuda.get_device_name(0))
else:
    print("CUDA NO disponible")


PyTorch version: 2.5.1+cu121
CUDA available: True
CUDA version: 12.1
GPU count: 1
GPU name: NVIDIA GeForce RTX 4070 SUPER


In [2]:
from ultralytics import YOLO

model = YOLO("yolov8n.pt")
print("Modelo cargado correctamente")


Modelo cargado correctamente


In [3]:
CLASS_NAMES = ['Small car', 'Bus', 'Truck', 'Building']

#### Training
Design and train a detector to deal with the “xview_detection” perception task.

In [4]:
from ultralytics import YOLO

model = YOLO("yolov8n.pt")

results = model.train(
    data="xview_yolo/data.yaml",
    epochs=80,
    imgsz=1024,
    batch=2,
    device=0,
    cos_lr=True,
    amp=False,        
    val=False
)



New https://pypi.org/project/ultralytics/8.3.248 available 😃 Update with 'pip install -U ultralytics'
Ultralytics 8.3.244 🚀 Python-3.10.19 torch-2.5.1+cu121 CUDA:0 (NVIDIA GeForce RTX 4070 SUPER, 12282MiB)
engine/trainer: agnostic_nms=False, amp=False, augment=False, auto_augment=randaugment, batch=2, bgr=0.0, box=7.5, cache=False, cfg=None, classes=None, close_mosaic=10, cls=0.5, compile=False, conf=None, copy_paste=0.0, copy_paste_mode=flip, cos_lr=True, cutmix=0.0, data=xview_yolo/data.yaml, degrees=0.0, deterministic=True, device=0, dfl=1.5, dnn=False, dropout=0.0, dynamic=False, embed=None, epochs=80, erasing=0.4, exist_ok=False, fliplr=0.5, flipud=0.0, format=torchscript, fraction=1.0, freeze=None, half=False, hsv_h=0.015, hsv_s=0.7, hsv_v=0.4, imgsz=1024, int8=False, iou=0.7, keras=False, kobj=1.0, line_width=None, lr0=0.01, lrf=0.01, mask_ratio=4, max_det=300, mixup=0.0, mode=train, model=yolov8n.pt, momentum=0.937, mosaic=1.0, multi_scale=False, name=train3, nbs=64, nms=False,

RuntimeError: Caught RuntimeError in pin memory thread for device 0.
Original Traceback (most recent call last):
  File "/home/user/conda/envs/yolo/lib/python3.10/site-packages/torch/utils/data/_utils/pin_memory.py", line 41, in do_one_step
    data = pin_memory(data, device)
  File "/home/user/conda/envs/yolo/lib/python3.10/site-packages/torch/utils/data/_utils/pin_memory.py", line 75, in pin_memory
    {k: pin_memory(sample, device) for k, sample in data.items()}
  File "/home/user/conda/envs/yolo/lib/python3.10/site-packages/torch/utils/data/_utils/pin_memory.py", line 75, in <dictcomp>
    {k: pin_memory(sample, device) for k, sample in data.items()}
  File "/home/user/conda/envs/yolo/lib/python3.10/site-packages/torch/utils/data/_utils/pin_memory.py", line 64, in pin_memory
    return data.pin_memory(device)
RuntimeError: CUDA error: out of memory
CUDA kernel errors might be asynchronously reported at some other API call, so the stacktrace below might be incorrect.
For debugging c

In [7]:
from ultralytics import YOLO

model = YOLO("runs/detect/train3/weights/best.pt")
print("Modelo cargado correctamente")


Modelo cargado correctamente


#### Validation
Compute validation metrics.

In [ ]:
from ultralytics import YOLO
import matplotlib.pyplot as plt
import numpy as np
from pathlib import Path

model = YOLO("runs/detect/train3/weights/best.pt")

metrics = model.val(
    data="xview_yolo/data.yaml",
    batch=4,
    device=0,
    plots=True  
)

print("=== MÉTRICAS DE VALIDACIÓN ===")
print(f"mPrecision: {metrics.box.mp:.4f}")
print(f"mRecall:    {metrics.box.mr:.4f}")
print(f"mAP@50:     {metrics.box.map50:.4f}")
print(f"mAP@50-95:  {metrics.box.map:.4f}")

mAccuracy = (metrics.box.mp + metrics.box.mr) / 2
print(f"mAccuracy (aprox): {mAccuracy:.4f}")

plots_dir = Path(metrics.save_dir)

print("\n📊 Mostrando gráficas de validación...")

imgs = [
    "confusion_matrix.png",
    "confusion_matrix_normalized.png",
    "PR_curve.png",
    "P_curve.png",
    "R_curve.png",
    "F1_curve.png"
]

for img in imgs:
    img_path = plots_dir / img
    if img_path.exists():
        plt.figure(figsize=(6, 6))
        plt.imshow(plt.imread(img_path))
        plt.axis("off")
        plt.title(img.replace("_", " ").replace(".png", ""))
        plt.show()



Ultralytics 8.3.244 🚀 Python-3.10.19 torch-2.5.1+cu121 CUDA:0 (NVIDIA GeForce RTX 4070 SUPER, 12282MiB)
Model summary (fused): 72 layers, 3,006,428 parameters, 0 gradients, 8.1 GFLOPs
val: Fast image access ✅ (ping: 0.0±0.0 ms, read: 660.1±97.9 MB/s, size: 1201.3 KB)
val: Scanning /home/user/projects/detection/xview_yolo/labels/val.cache... 761 images, 0 backgrounds, 0 corrupt: 100% ━━━━━━━━━━━━ 761/761 1.7Mit/s 0.0s0s
                 Class     Images  Instances      Box(P          R      mAP50  mAP50-95): 100% ━━━━━━━━━━━━ 191/191 20.5it/s 9.3s0.1s
                   all        761      48944       0.55      0.553      0.535      0.268
             Small car        650      17948      0.714      0.813      0.778      0.336
                   Bus        201        600      0.473      0.467      0.454      0.237
                 Truck        282       1112      0.389      0.297      0.276       0.15
              Building        722      29284      0.622      0.635      0.634      0.34

<Figure size 600x600 with 1 Axes>

<Figure size 600x600 with 1 Axes>

#### Testing
Try to improve the results provided in the competition.

In [ ]:
import json
from pathlib import Path
from ultralytics import YOLO
import tifffile as tiff

MODEL_PATH = "runs/detect/train3/weights/best.pt"
TEST_IMG_DIR = Path("xview_yolo/images/test")
OUT_JSON = "prediction.json"

categories = {
    0: "Small car",
    1: "Bus",
    2: "Truck",
    3: "Building"
}

model = YOLO(MODEL_PATH)

predictions_data = {
    "images": {},
    "annotations": {},
    "categories": categories
}

img_idx = 0
ann_idx = 0

for img_path in sorted(TEST_IMG_DIR.glob("*.tif")):
    results = model.predict(
    source=str(img_path),
        imgsz=1024,     
        conf=0.2,       
        iou=0.7,         
        device=0,
        verbose=False
    )

    
    r = results[0]
    print(r.boxes)

    # Tamaño real
    img = tiff.imread(img_path)
    h, w = img.shape[:2]

    boxes = results[0].boxes
    num_objects = 0 if boxes is None else len(boxes)

    predictions_data["images"][img_idx] = {
        "image_id": img_path.name,
        "filename": f"xview_test/{img_path.name}",
        "num_objects": num_objects,
        "width": w,
        "height": h
    }

    if boxes is not None:
        for box in boxes:
            cls_id = int(box.cls.item())
            conf = float(box.conf.item())
            x1, y1, x2, y2 = box.xyxy[0].tolist()

            predictions_data["annotations"][ann_idx] = {
                "image_id": img_path.name,
                "category_id": categories[cls_id],
                "bbox": [
                    int(x1),
                    int(y1),
                    int(x2),
                    int(y2)
                ],
                "confidence": f"{conf:.4f}"
            }
            ann_idx += 1

    img_idx += 1

with open(OUT_JSON, "w") as f:
    json.dump(predictions_data, f)

print(f"✅ prediction.json generado")
print(f"📸 Imágenes procesadas: {img_idx}")
print(f"🏷️ Detecciones totales: {ann_idx}")


ultralytics.engine.results.Boxes object with attributes:

cls: tensor([3., 3., 3., 3., 3., 3., 3., 3.], device='cuda:0')
conf: tensor([0.5958, 0.5136, 0.5103, 0.4684, 0.4005, 0.3966, 0.3813, 0.3559], device='cuda:0')
data: tensor([[1.2101e+01, 2.3382e+01, 1.5399e+02, 1.2226e+02, 5.9579e-01, 3.0000e+00],
        [6.6720e+01, 3.7322e+02, 1.3307e+02, 4.3457e+02, 5.1358e-01, 3.0000e+00],
        [7.1490e+01, 1.0689e+02, 2.4866e+02, 3.7964e+02, 5.1033e-01, 3.0000e+00],
        [7.9087e-01, 5.1678e+02, 7.3631e+01, 5.9814e+02, 4.6835e-01, 3.0000e+00],
        [4.6872e+01, 3.0645e+02, 8.3428e+01, 3.5802e+02, 4.0055e-01, 3.0000e+00],
        [0.0000e+00, 4.2818e+02, 7.3365e+01, 4.8650e+02, 3.9662e-01, 3.0000e+00],
        [6.3545e+01, 3.3621e+02, 1.5087e+02, 3.9210e+02, 3.8132e-01, 3.0000e+00],
        [0.0000e+00, 8.7312e+01, 1.1699e+02, 2.3460e+02, 3.5588e-01, 3.0000e+00]], device='cuda:0')
id: None
is_track: False
orig_shape: (640, 640)
shape: torch.Size([8, 6])
xywh: tensor([[ 83.0457,  72.